# Installing Required Packages

In [1]:
# pip install requests

In [2]:
# pip install ipyparallel

# Importing the packages


In [3]:
import os

In [4]:
import logging

In [5]:
import requests

In [6]:
import sqlite3 as _dbsql

In [7]:
from pathlib import Path

In [8]:
from http.server import BaseHTTPRequestHandler, HTTPServer

# Execution Constants and Variables

In [9]:
_db_root = "Database"

In [10]:
_dir = Path().resolve()

In [11]:
_log = logging.getLogger(__name__)
_log.setLevel(logging.DEBUG)
iohandler = logging.StreamHandler()
iohandler.setLevel(logging.DEBUG)
formatter = logging.Formatter('%(asctime)s - %(name)s - %(levelname)s - %(message)s')
iohandler.setFormatter(formatter)
_log.addHandler(iohandler)
logging.basicConfig(filename="execution_log.log", filemode='w')

# Changing path to current directory (Execute only once)

In [12]:
try:
    os.chdir(_dir)
    _db_root_check = os.path.isdir(_db_root)
    if not _db_root_check:
        os.makedirs(_db_root)
    _db_path = os.path.join(_dir, _db_root)
    os.chdir(_db_path)
    _log.info("database root initialised successfully")
except Exception as _initialization_exception:
    _log.critical("root path could not be initialised")

2022-05-08 17:42:29,427 - __main__ - INFO - database root initialised successfully


# Database Initialization

In [13]:
try:
    _db_con = _dbsql.connect('inm_warehouse.db')
    _log.info("database inm_warehouse.db initialised successfully")
except Exception as _db_initialization:
    _log.critical("database could not be initialised")

2022-05-08 17:42:29,441 - __main__ - INFO - database inm_warehouse.db initialised successfully


In [14]:
try:
    _db_cursor = _db_con.cursor()
    _db_cursor.execute('''CREATE TABLE warehouse
               (device_name text not null, timestamp text not null, data text not null)''')
    _log.info("database table creation successful")
except Exception as _db_exception:
    _log.warning("database table could not be initialised: " + str(_db_exception))

2022-05-08 17:42:29,456 - __main__ - INFO - database table creation successful


# Get Descriptor for a node name from OM2M

In [15]:
def get_descriptor(Node_name):
        url = "http://127.0.0.1:5089/~/in-cse/in-name/AE-TEST/" + Node_name + "/Descriptor/la"

        payload={}
        headers = {
          'X-M2M-Origin': 'admin:admin',
          'Accept': 'application/json'
        }
        response = requests.request("GET", url, headers=headers, data=payload)
        if response.status_code != 200:
            _log.warning("device not found")
            return False, None
        _data = eval(response.text)
        _con = _data["m2m:cin"]["con"].replace(" ", "")
        _con = _con.split("[")[1]
        _con = _con.split("]")[0]
        _con = _con.split(",")
        _log.info("data retrieved from om2m")
        return True, _con

# Get data from database for a given node-name

In [16]:
def get_from_db(_node_name):
    name = "'" + _node_name + "'"
    _data = _db_cursor.execute('SELECT * FROM warehouse where device_name =' + name)
    _log.info("data retrieved from db")
    return _data

# Server Class for data warehousing

In [17]:
class handler(BaseHTTPRequestHandler):
    
    
    def do_GET(self):
        
        if "/ngsi-ld/v1/entities/" in self.path:
            _node_name = self.path.split("/ngsi-ld/v1/entities/")[1]
            _parameter_list = ["node_id"]
            _om2m_status = get_descriptor(_node_name)
            
            if not _om2m_status[0]:
                self.send_response(404)
                response = "{\"type\":\"urn:dx:rs:general\",\"title\":\"Device Not Registered\",\"detail\":\"Device Not Registered\"}"
            
            else:
                _lis = []
                self.send_response(200)
                _parameter_list += _om2m_status[1]
                _log.info(_parameter_list)
                response = "{\"title\": \"Successful operation\", \"type\": \"urn:dx:rs:success\", \"results\": ["
                
                _data = get_from_db(_node_name)
                for row in _data:
                    _log.info(row)
                    _lis += [row]
                _ordered_data = list(reversed(_lis))
                length_of_data = len(_ordered_data)
                for row_id in range(length_of_data):
                    _current_row = [_node_name]
                    _current_row += eval(list(_ordered_data[row_id])[2])
                    response += "{"
                    _data_length = len(_parameter_list)
                    
                    for parameter_id in range(_data_length):
                        response += "\"" + _parameter_list[parameter_id] + "\":" + "\"" + str(_current_row[parameter_id])
                        
                        if parameter_id == _data_length -1:
                            response += "\""
                        
                        else:
                            response += "\","
                    
                    if row_id == length_of_data -1:
                        response += "}"
                    
                    else:
                        response += "},"
                
                response += "]}"
                _log.info("data formatting successsful")
                    
        else:
            _log.warning("url-end point not found")
            self.send_response(404)
            response = "{\"type\":\"urn:dx:rs:general\",\"title\":\"NotFound\",\"detail\":\"NotFound\"}"
            
        self.send_header('Content-type','application/json')
        self.end_headers()
        self.wfile.write(bytes(response, "utf8"))
    
    def do_POST(self):
        self.data_string = self.rfile.read(int(self.headers['Content-Length'])).decode("utf-8")
        self.send_response(200)
        self.send_header('Content-type','text/html')
        self.end_headers()
        try:
            print(self.data_string)
            var = self.data_string.replace("false", "False" )
            var = eval(var.replace("true", "True" ))
            _con = eval(var["m2m:sgn"]["m2m:nev"]["m2m:rep"]["m2m:cin"]["con"])
            _lbl = var["m2m:sgn"]["m2m:nev"]["m2m:rep"]["m2m:cin"]["lbl"]
            _values = (str(_lbl[0]), str(_con[0]), str(_con))
            _query = "INSERT INTO warehouse VALUES " + str(_values)
            _db_cursor.execute(_query)
            _log.info("data stored with query: " + str(_query))
        except Exception as ioerror:
            _log.critical("data storage failed with exception: " + str(ioerror))
        
        message = "{\"Status\": 200}"
        self.wfile.write(bytes(message, "utf8"))

In [ ]:
with HTTPServer(('', 5091), handler) as server:
        server.serve_forever()

127.0.0.1 - - [08/May/2022 17:43:25] "POST / HTTP/1.1" 200 -
2022-05-08 17:43:25,436 - __main__ - CRITICAL - data storage failed with exception: 'm2m:nev'
127.0.0.1 - - [08/May/2022 17:43:25] "POST / HTTP/1.1" 200 -
2022-05-08 17:43:25,468 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012005', '[1652012005, 0, 39]')
127.0.0.1 - - [08/May/2022 17:43:25] "POST / HTTP/1.1" 200 -
2022-05-08 17:43:25,587 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012005', '[1652012005, 1, 97]')


{
   "m2m:sgn" : {
      "m2m:vrq" : true,
      "m2m:sud" : false
   }
}
{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_92159222",
               "ty" : 4,
               "ri" : "/in-cse/cin-92159222",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174325",
               "lt" : "20220508T174325",
               "lbl" : [ "Node-1" ],
               "st" : 0,
               "cnf" : "text",
               "cs" : 19,
               "con" : "[1652012005, 0, 39]"
            }
         },
         "m2m:rss" : 1
      },
      "m2m:sud" : false,
      "m2m:sur" : "/in-cse/sub-524524193"
   }
}
{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_128785026",
               "ty" : 4,
               "ri" : "/in-cse/cin-128785026",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174325",
               "l

127.0.0.1 - - [08/May/2022 17:43:25] "POST / HTTP/1.1" 200 -
2022-05-08 17:43:25,715 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012005', '[1652012005, 1, 76]')
127.0.0.1 - - [08/May/2022 17:43:25] "POST / HTTP/1.1" 200 -
2022-05-08 17:43:25,839 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012005', '[1652012005, 1, 261]')


{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_701924230",
               "ty" : 4,
               "ri" : "/in-cse/cin-701924230",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174325",
               "lt" : "20220508T174325",
               "lbl" : [ "Node-1" ],
               "st" : 0,
               "cnf" : "text",
               "cs" : 19,
               "con" : "[1652012005, 1, 76]"
            }
         },
         "m2m:rss" : 1
      },
      "m2m:sud" : false,
      "m2m:sur" : "/in-cse/sub-524524193"
   }
}
{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_48453132",
               "ty" : 4,
               "ri" : "/in-cse/cin-48453132",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174325",
               "lt" : "20220508T174325",
               "lbl" : [ "Node-1" ],
             

127.0.0.1 - - [08/May/2022 17:43:25] "POST / HTTP/1.1" 200 -
2022-05-08 17:43:25,960 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012005', '[1652012005, 0, 140]')
127.0.0.1 - - [08/May/2022 17:43:26] "POST / HTTP/1.1" 200 -
2022-05-08 17:43:26,085 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012006', '[1652012006, 1, 262]')


...

2022-05-08 17:48:33,466 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012312', '[1652012312, 1, 206]')
127.0.0.1 - - [08/May/2022 17:48:33] "POST / HTTP/1.1" 200 -
2022-05-08 17:48:33,482 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012312', '[1652012312, 1, 152]')
127.0.0.1 - - [08/May/2022 17:48:33] "POST / HTTP/1.1" 200 -
2022-05-08 17:48:33,528 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012312', '[1652012312, 1, 212]')
127.0.0.1 - - [08/May/2022 17:48:33] "POST / HTTP/1.1" 200 -
2022-05-08 17:48:33,542 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012311', '[1652012311, 1, 113]')
127.0.0.1 - - [08/May/2022 17:48:33] "POST / HTTP/1.1" 200 -
2022-05-08 17:48:33,549 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012313', '[1652012313, 0, 358]')
127.0.0.1 - - [08/May/2022

{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_825642522",
               "ty" : 4,
               "ri" : "/in-cse/cin-825642522",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174832",
               "lt" : "20220508T174832",
               "lbl" : [ "Node-1" ],
               "st" : 0,
               "cnf" : "text",
               "cs" : 20,
               "con" : "[1652012312, 1, 206]"
            }
         },
         "m2m:rss" : 1
      },
      "m2m:sud" : false,
      "m2m:sur" : "/in-cse/sub-524524193"
   }
}
{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_825144384",
               "ty" : 4,
               "ri" : "/in-cse/cin-825144384",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174832",
               "lt" : "20220508T174832",
               "lbl" : [ "Node-1" ],
          

2022-05-08 17:48:33,671 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012313', '[1652012313, 1, 8]')
127.0.0.1 - - [08/May/2022 17:48:33] "POST / HTTP/1.1" 200 -
2022-05-08 17:48:33,778 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012313', '[1652012313, 1, 375]')
127.0.0.1 - - [08/May/2022 17:48:33] "POST / HTTP/1.1" 200 -
2022-05-08 17:48:33,885 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012313', '[1652012313, 0, 11]')


{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_521237647",
               "ty" : 4,
               "ri" : "/in-cse/cin-521237647",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174833",
               "lt" : "20220508T174833",
               "lbl" : [ "Node-1" ],
               "st" : 0,
               "cnf" : "text",
               "cs" : 18,
               "con" : "[1652012313, 1, 8]"
            }
         },
         "m2m:rss" : 1
      },
      "m2m:sud" : false,
      "m2m:sur" : "/in-cse/sub-524524193"
   }
}
{
   "m2m:sgn" : {
      "m2m:nev" : {
         "m2m:rep" : {
            "m2m:cin" : {
               "rn" : "cin_371719379",
               "ty" : 4,
               "ri" : "/in-cse/cin-371719379",
               "pi" : "/in-cse/cnt-686532010",
               "ct" : "20220508T174833",
               "lt" : "20220508T174833",
               "lbl" : [ "Node-1" ],
            

127.0.0.1 - - [08/May/2022 17:48:34] "POST / HTTP/1.1" 200 -
2022-05-08 17:48:34,007 - __main__ - INFO - data stored with query: INSERT INTO warehouse VALUES ('Node-1', '1652012313', '[1652012313, 1, 73]')
